# Análise Exploratória

In [1]:
import sys
import numpy as np
import seaborn as sns
import pandas as pd
np.set_printoptions(threshold=sys.maxsize)
pd.set_option('display.max_columns', None)
pd.set_option('display.max_rows', None)
pd.set_option('display.max_colwidth', 80)
def id_like_dtypes(path):
    """Detecta colunas de identificação/código, CPF e CNPJ pelo nome e monta
    um dict de dtype=str para evitar perda de zeros à esquerda na leitura."""
    header = pd.read_csv(path, nrows=0).columns
    dtypes = {}
    for col in header:
        c = col.lower()
        is_id = (
            "codigo" in c or "cnpj" in c or "cpf" in c
            or c.startswith(("id", "numero", "sequencial", "cod"))
            or c.endswith(("id", "idpncp"))
            or c in {"nifornecedor"}
        )
        if is_id:
            dtypes[col] = str
    return dtypes


def read_csv_ids_str(path, dtype=None, **kwargs):
    """pd.read_csv que força colunas de identificação/código/CPF/CNPJ como string."""
    dtypes = id_like_dtypes(path)
    if dtype:
        dtypes.update(dtype)
    return pd.read_csv(path, dtype=dtypes, **kwargs)

In [2]:
raw_orgao = read_csv_ids_str('raw_orgao_202607071236.csv')
raw_uasg = read_csv_ids_str('raw_uasg_202607071236.csv')

# Domínio 3: Órgãos e UASGs


```mermaid
erDiagram
    raw_orgao {
        text codigoorgao PK
        text nomeorgao
        text poder
        text esfera
    }
    raw_uasg {
        text codigouasg PK
        text codigoorgao FK
        text nomeuasg
        text siglauf
    }
    raw_contratacoes {
        text idcompra PK
        text codigoorgao FK
        text objetocompra
        text modalidadenome
        text valortotalhomologado
        text datapublicacaopncp
    }
    raw_itens_contratacoes {
        text idcompraitem PK
        text idcompra FK
        text descricaoresumida
        text materialouservico
        text coditemcatalogo
        text quantidade
        text valorunitarioestimado
    }
    raw_resultado_itens_contratacoes {
        text idcompraitem FK
        text sequencialresultado PK
        text nifornecedor
        text nomerazaosocialfornecedor
        text quantidadehomologada
        text valorunitariohomologado
    }
    raw_contratos {
        text codigounidadegestora PK
        text numerocontrato PK
        text nifornecedor PK
        text codigoorgao FK
        text idcompra FK
        text objeto
        text valorglobal
        text datavigenciainicial
        text datavigenciafinal
    }
    raw_contratos_item {
        text codigounidadegestora FK
        text numerocontrato FK
        text nifornecedor FK
        text numeroitem PK
        text contratoitemexcluido PK
        text codigoitem
        text descricaoiitem
        text quantidadeitem
        text valorunitarioitem
    }
    raw_arp {
        text numeroataregistropreco PK
        text idcompra PK
        text codigoorgao FK
        text valortotal
        text datavigenciainicial
        text datavigenciafinal
        text statusata
    }
    raw_arp_item {
        text numeroataregistropreco FK
        text codigounidadegerenciadora
        text numeroitem
        text idcompra
        text nifornecedor
        text codigoitem
        text descricaoitem
        text quantidadehomologadaitem
        text valorunitario
    }
    raw_arp_unidades_item {
        text numeroataregistropreco FK
        text codigounidadegerenciadora FK
        text numeroitem FK
        text codigounidade
        text nomeunidade
        text quantidaderegistrada
        text saldoadesoes
    }
    raw_arp_adesoes_item {
        text numeroataregistropreco FK
        text codigounidadegerenciadora FK
        text numeroitem FK
        text unidadenaoparticipante
        text quantidadeaprovadaadesao
        text dataaprovacaoanalise
    }
    raw_arp_empenhos_saldo {
        text numeroataregistropreco FK
        text codigounidadegerenciadora FK
        text tipo
        text quantidaderegistrada
        text quantidadeempenhada
        text saldoempenho
    }

    raw_orgao ||--o{ raw_uasg : "codigoorgao"
    raw_orgao ||--o{ raw_contratacoes : "codigoorgao"
    raw_orgao ||--o{ raw_contratos : "codigoorgao"
    raw_contratacoes ||--o{ raw_itens_contratacoes : "idcompra"
    raw_itens_contratacoes ||--o{ raw_resultado_itens_contratacoes : "idcompraitem"
    raw_contratacoes ||--o{ raw_contratos : "idcompra"
    raw_contratos ||--o{ raw_contratos_item : "ug + numerocontrato + nifornecedor"
    raw_contratacoes ||--o{ raw_arp : "idcompra"
    raw_arp ||--o{ raw_arp_item : "numeroataregistropreco"
    raw_arp_item ||--o{ raw_arp_unidades_item : "ata + ug + item"
    raw_arp_item ||--o{ raw_arp_adesoes_item : "ata + ug + item"
    raw_arp_item ||--o{ raw_arp_empenhos_saldo : "ata + ug"
```


## `raw_orgao`
Cadastro de órgãos da administração pública federal.

| Coluna | Descrição |
|---|---|
| `codigoorgao` **PK** | Código do órgão (SIORG) |
| `nomeorgao` | Nome do órgão |
| `nomemnemonicoorgao` | Nome abreviado (sigla) |
| `cnpjcpforgao` | CNPJ do órgão |
| `codigoorgaovinculado` | Código do órgão ao qual está vinculado |
| `codigoorgaosuperior` | Código do órgão superior hierárquico |
| `codigotipoadministracao` | Tipo de administração |
| `poder` | Executivo, Legislativo, Judiciário |
| `esfera` | Federal, Estadual, Municipal |
| `statusorgao` | Ativo/inativo |

In [3]:
raw_orgao.shape

(11820, 18)

In [4]:
raw_orgao.duplicated().sum()

0

### `codigoorgao`
Código do órgão

In [5]:
raw_orgao.codigoorgao.duplicated().sum()

0

#### 11820 órgãos cadastrados

In [6]:
raw_orgao.head()

,codigoorgao,nomeorgao,nomemnemonicoorgao,cnpjcpforgao,codigoorgaovinculado,cnpjcpforgaovinculado,nomeorgaovinculado,codigoorgaosuperior,cnpjcpforgaosuperior,nomeorgaosuperior,codigotipoadministracao,nometipoadministracao,poder,esfera,usosisg,statusorgao,datahoramovimento,dt_ingest
0,77105,MRS-CÂMARA MUNICIPAL DE SAO BORJA,CMSB,90791997000138,NaN,NaN,NaN,NaN,NaN,NaN,12,ADMINISTRACAO DIRETA MUNICIPAL,E,M,True,True,2026-06-12T08:50:00,2026-06-27T04:01:46.962946
1,96343,PREFEITURA MUN. DE MATO CASTELHANO,PMMC,92412808000102,NaN,NaN,NaN,NaN,NaN,NaN,12,ADMINISTRACAO DIRETA MUNICIPAL,E,M,True,True,2024-02-21T10:46:00,2026-06-27T04:01:46.962946
2,13002,AUDITORIA DA 10A. CJM / JUSTICA MILITAR - CE,AUD. 10A. CJM,00497552002109,NaN,NaN,NaN,NaN,NaN,NaN,1,ADMINISTRACAO DIRETA,E,F,True,True,2025-02-21T17:25:00,2026-06-27T04:01:16.491123
3,15000,JUSTICA DO TRABALHO,TST,00509968000148,NaN,NaN,NaN,NaN,NaN,NaN,1,ADMINISTRACAO DIRETA,L,F,False,True,2026-05-26T11:49:00,2026-06-27T04:01:16.491123
4,95695,PREFEITURA MUNICIPAL DE CAMPINAS - SP,PM DE CAMPINAS - SP,51885242000140,95420.0,46379400000150,ESP-ESTADO DE SÃO PAULO,95000.0,0,REGIAO SUDESTE,12,ADMINISTRACAO DIRETA MUNICIPAL,E,M,True,True,2024-01-07T13:57:00,2026-06-27T04:01:43.018081


### `codigoorgaovinculado`
Código do órgão vinculado

In [7]:
raw_orgao.codigoorgaovinculado.value_counts(True, dropna=False).head()

codigoorgaovinculado
NaN        0.108037
95420.0    0.069628
95120.0    0.046785
96120.0    0.046447
94520.0    0.045601
Name: proportion, dtype: float64

#### 10% dos órgãos não possuem orgão vinculado.

### `cnpjcpforgao`
CNPJ do órgão

In [8]:
len(raw_orgao.cnpjcpforgao.unique())

11501

In [9]:
11820 - 11500

320

In [10]:
raw_orgao.cnpjcpforgao.value_counts(False, dropna=False).head()

cnpjcpforgao
0                 40
00394460000141     9
00394494000136     7
03353358000196     7
00394411000109     5
Name: count, dtype: int64

#### 40 orgãos tem cnpj 0, 280 orgão tem o mesmo cnpj do seu orgão superior.

#### O mesmo órgão pode estar registrado várias vezes, portanto não é possível considerar as porcentagens a seguir sem ajustes.
Exemplos a seguir.

#### (TO DO) Observações dos órgão com mesmo cnpj
- Deu pra perceber que tem 3 códigos de órgão para a presidência da república, um igual ao código do órgão superior, outro para o código do órgão vinculado e um para o código orgão.

In [11]:
raw_orgao[raw_orgao.cnpjcpforgao.duplicated(keep=False)].sort_values(by='cnpjcpforgao')

,codigoorgao,nomeorgao,nomemnemonicoorgao,cnpjcpforgao,codigoorgaovinculado,cnpjcpforgaovinculado,nomeorgaovinculado,codigoorgaosuperior,cnpjcpforgaosuperior,nomeorgaosuperior,codigotipoadministracao,nometipoadministracao,poder,esfera,usosisg,statusorgao,datahoramovimento,dt_ingest
44,91800,ORGANIZACOES SOCIAIS,ORGANIZ. SOCIAIS,0,NaN,NaN,NaN,NaN,NaN,NaN,15,EMPRESA PRIVADA,E,NaN,True,True,2007-11-30T23:00:00,2026-06-27T04:01:16.491123
91,25907,FUNDO CONST.DE FINANCIAMENTO-FNO - INTEGRACAO,FNO,0,25000.0,00394460000141,MINISTERIO DA FAZENDA,20101.0,00394411000109,PRESIDENCIA DA REPUBLICA,7,FUNDOS,E,NaN,True,True,2007-11-30T23:00:00,2026-06-27T04:01:16.491123
92,25910,FUNDO CONSTIT.FINANC.DO NORDESTE-FNE-INTEG.,FNE-INTEGRACAO,0,25000.0,00394460000141,MINISTERIO DA FAZENDA,20101.0,00394411000109,PRESIDENCIA DA REPUBLICA,7,FUNDOS,E,NaN,True,True,2007-11-30T23:00:00,2026-06-27T04:01:16.491123
93,80210,EMPRESA BRAS.DE ASSISTENCIA TEC.E EXT.RURAL,EMBRATER,0,22000.0,00396895000125,MINISTERIO DA AGRICULTURA E PECUARIA - MAPA,20101.0,00394411000109,PRESIDENCIA DA REPUBLICA,5,EMPRESA PUBLICA COMERCIAL E FINANCEIRA,E,NaN,True,True,2007-11-30T23:00:00,2026-06-27T04:01:16.491123
94,20107,SECRETARIA DA CULTURA,SEC.CULTURA,0,20000.0,00394411000109,PRESIDENCIA DA REPUBLICA - PRES,NaN,NaN,NaN,1,ADMINISTRACAO DIRETA,E,NaN,True,True,2001-11-28T02:00:00,2026-06-27T04:01:16.491123
95,20108,SECRETARIA DA CIENCIA E TECNOLOGIA,SCT,0,24000.0,01263896000164,"MINISTERIO DA CIENCIA,TECNOLOGIA E INOVAÇÃO",20101.0,00394411000109,PRESIDENCIA DA REPUBLICA,1,ADMINISTRACAO DIRETA,E,NaN,True,True,2000-02-29T09:34:00,2026-06-27T04:01:16.491123
96,20103,MINISTERIO ADM.FED.REFORMA ESTADO-EM EXTINCAO,MARE-EM EXTINCAO,0,NaN,NaN,NaN,NaN,NaN,NaN,1,ADMINISTRACAO DIRETA,E,NaN,True,True,2007-11-30T23:00:00,2026-06-27T04:01:16.491123
97,25903,FUNDO DE INVESTIMENTO DA AMAZONIA,FINAM,0,53000.0,03353358000196,MINISTÉRIO DA INTEGRAÇÃO E DESENV. REGIONAL,20101.0,00394411000109,PRESIDENCIA DA REPUBLICA,7,FUNDOS,E,NaN,True,True,2007-11-30T23:00:00,2026-06-27T04:01:16.491123
98,45282,BANCO NACIONAL DE DESENV. ECONOMICO E SOCIAL,BNDES,0,28000.0,00394478000143,"MINISTERIO DO DESENV,IND.COMERCIO E SERVIÇOS",20101.0,00394411000109,PRESIDENCIA DA REPUBLICA,5,EMPRESA PUBLICA COMERCIAL E FINANCEIRA,E,NaN,True,True,2007-11-30T23:00:00,2026-06-27T04:01:16.491123
99,25902,FUNDO DE INVESTIMENTO DO NORDESTE,FINOR,0,53000.0,03353358000196,MINISTÉRIO DA INTEGRAÇÃO E DESENV. REGIONAL,20101.0,00394411000109,PRESIDENCIA DA REPUBLICA,7,FUNDOS,E,NaN,True,True,2007-11-30T23:00:00,2026-06-27T04:01:16.491123


#### (TO DO) Observações dos órgão com a mesma sigla
- Códigos `20102` e `60000` se referem à `GABINETE DA VICE-PRESIDENCIA DA REPUBLICA	` e `GABINETE DA VICE-PRESIDENCIA DA REPUBLICA 2`, respectivamente.

In [12]:
raw_orgao

,codigoorgao,nomeorgao,nomemnemonicoorgao,cnpjcpforgao,codigoorgaovinculado,cnpjcpforgaovinculado,nomeorgaovinculado,codigoorgaosuperior,cnpjcpforgaosuperior,nomeorgaosuperior,codigotipoadministracao,nometipoadministracao,poder,esfera,usosisg,statusorgao,datahoramovimento,dt_ingest
0,77105,MRS-CÂMARA MUNICIPAL DE SAO BORJA,CMSB,90791997000138,NaN,NaN,NaN,NaN,NaN,NaN,12,ADMINISTRACAO DIRETA MUNICIPAL,E,M,True,True,2026-06-12T08:50:00,2026-06-27T04:01:46.962946
1,96343,PREFEITURA MUN. DE MATO CASTELHANO,PMMC,92412808000102,NaN,NaN,NaN,NaN,NaN,NaN,12,ADMINISTRACAO DIRETA MUNICIPAL,E,M,True,True,2024-02-21T10:46:00,2026-06-27T04:01:46.962946
2,13002,AUDITORIA DA 10A. CJM / JUSTICA MILITAR - CE,AUD. 10A. CJM,00497552002109,NaN,NaN,NaN,NaN,NaN,NaN,1,ADMINISTRACAO DIRETA,E,F,True,True,2025-02-21T17:25:00,2026-06-27T04:01:16.491123
3,15000,JUSTICA DO TRABALHO,TST,00509968000148,NaN,NaN,NaN,NaN,NaN,NaN,1,ADMINISTRACAO DIRETA,L,F,False,True,2026-05-26T11:49:00,2026-06-27T04:01:16.491123
4,95695,PREFEITURA MUNICIPAL DE CAMPINAS - SP,PM DE CAMPINAS - SP,51885242000140,95420.0,46379400000150,ESP-ESTADO DE SÃO PAULO,95000.0,0,REGIAO SUDESTE,12,ADMINISTRACAO DIRETA MUNICIPAL,E,M,True,True,2024-01-07T13:57:00,2026-06-27T04:01:43.018081
5,95823,CAMARA MUNICIPAL DE INDAIATUBA - SP,CM DE INDAIATUBA-SP,51907384000161,95420.0,46379400000150,ESP-ESTADO DE SÃO PAULO,95000.0,0,REGIAO SUDESTE,12,ADMINISTRACAO DIRETA MUNICIPAL,NaN,M,True,True,2024-01-13T13:57:00,2026-06-27T04:01:43.018081
6,95670,CAMARA MUNICIPAL DE BOM JESUS DOS PERDOES-SP,CM BOM J. PERDOES,51913804000112,95420.0,46379400000150,ESP-ESTADO DE SÃO PAULO,95000.0,0,REGIAO SUDESTE,12,ADMINISTRACAO DIRETA MUNICIPAL,NaN,M,True,True,2024-01-07T13:57:00,2026-06-27T04:01:43.018081
7,86390,EDF-ADMINISTRAÇAO REGIONAL DE ARAPONGA,RA ARAPONGA/DF,51959349000196,97400.0,00394601000126,EDF-DISTRITO FEDERAL,97000.0,0,REGIAO CENTRO-OESTE,11,ADMINISTRACAO DIRETA ESTADUAL,E,E,True,True,2026-04-15T12:10:00,2026-06-27T04:01:43.018081
8,85126,"EAM-SECRETARIA DE EST ENERGIA,MINERAÇÃO E GÁS",SEMIG/AM,51999904000103,93320.0,04312369000190,EAM-ESTADO DO AMAZONAS,93000.0,0,REGIAO NORTE,11,ADMINISTRACAO DIRETA ESTADUAL,E,E,True,True,2026-01-30T11:08:00,2026-06-27T04:01:43.018081
9,85260,MRJ-FUNDO MUNICIPAL DE EDUCAÇÃO DE QUEIMADOS,FME/RJ,52020762000153,99044.0,39485412000102,MRJ-PREFEITURA MUNICIPAL DE QUEIMADOS,95320.0,42498600000171,ERJ-ESTADO DO RIO DE JANEIRO,7,FUNDOS,E,M,True,True,2026-03-26T13:23:00,2026-06-27T04:01:43.018081


### `nomemnemonicoorgao`
Mnemônico do órgão

In [13]:
raw_orgao[raw_orgao.nomemnemonicoorgao.duplicated(keep=False)].sort_values(by='nomemnemonicoorgao').head()

,codigoorgao,nomeorgao,nomemnemonicoorgao,cnpjcpforgao,codigoorgaovinculado,cnpjcpforgaovinculado,nomeorgaovinculado,codigoorgaosuperior,cnpjcpforgaosuperior,nomeorgaosuperior,codigotipoadministracao,nometipoadministracao,poder,esfera,usosisg,statusorgao,datahoramovimento,dt_ingest
923,82824,ETO-ASSOCIAÇÃO AP. ESC EST JOSÉ COSTA SOARES,AAEE/TO,01421200000180,93720.0,87252045000131,ETO-ESTADO DE TOCANTINS,93000.0,0,REGIAO NORTE,15,EMPRESA PRIVADA,E,E,True,True,2026-06-10T14:57:00,2026-06-27T04:01:18.099781
1492,82828,ETO-ASSOCIAÇÃO A. ESC EST. REZENDE DE ALMEIDA,AAEE/TO,01643863000140,93720.0,87252045000131,ETO-ESTADO DE TOCANTINS,93000.0,0,REGIAO NORTE,15,EMPRESA PRIVADA,E,E,True,True,2026-06-10T15:00:00,2026-06-27T04:01:19.359101
4566,82819,ETO-ASSOCIAÇÃO APOIO ESC ESPECIAL EDSON DUTRA,AAEE/TO,09405159000160,93720.0,87252045000131,ETO-ESTADO DE TOCANTINS,93000.0,0,REGIAO NORTE,15,EMPRESA PRIVADA,E,E,True,True,2026-06-10T14:52:00,2026-06-27T04:01:27.604210
8155,82834,CTO-ASSOCIAÇÃO C.CEI ANA L. ARAÚJO NAPUNUCENO,ACCEI/TO,24578154000123,82975.0,24851511000185,MTO-PREFEITURA MUNICIPAL DE PALMAS,93720.0,87252045000131,ETO-ESTADO DE TOCANTINS,15,EMPRESA PRIVADA,E,M,True,True,2026-06-10T15:14:00,2026-06-27T04:01:36.582425
3486,82835,CTO-ASSOCIAÇÃO COMUN. C.E.I CANTIGA DE NINAR,ACCEI/TO,06307119000198,82975.0,24851511000185,MTO-PREFEITURA MUNICIPAL DE PALMAS,93720.0,87252045000131,ETO-ESTADO DE TOCANTINS,15,EMPRESA PRIVADA,E,M,True,True,2026-06-10T15:15:00,2026-06-27T04:01:24.614930


### `nometipoadministracao`
Nome do tipo de administração do órgão

In [14]:
raw_orgao.nometipoadministracao.value_counts(True, dropna=False)

nometipoadministracao
ADMINISTRACAO DIRETA MUNICIPAL            0.428173
FUNDOS                                    0.161252
AUTARQUIA                                 0.122589
ADMINISTRACAO DIRETA ESTADUAL             0.080711
EMPRESA PRIVADA                           0.075635
FUNDACAO                                  0.033418
ADMINISTRACAO INDIRETA ESTADUAL           0.030372
ADMINISTRACAO INDIRETA MUNICIPAL          0.025127
EMPRESA PUBLICA COMERCIAL E FINANCEIRA    0.016836
ECONOMIA MISTA                            0.014129
ADMINISTRACAO DIRETA                      0.010914
EMPRESA PUBLICA INDUSTRIAL E AGRICOLA     0.000592
ESTATAL                                   0.000254
Name: proportion, dtype: float64

### `poder`
Poder ao qual o órgão pertence (E – Executivo, L – Legislativo, J – Judiciário)

In [15]:
raw_orgao.poder.value_counts(False, dropna=False)

poder
E      11318
NaN      484
L         18
Name: count, dtype: int64

In [16]:
raw_orgao.poder.value_counts(True, dropna=False)

poder
E      0.957530
NaN    0.040948
L      0.001523
Name: proportion, dtype: float64

#### Na coluna `poder` não há valores para o judiciário (TO DO: conferir pq acho q vi um tribunal na tabela `raw_uasg`)

In [17]:
raw_orgao[raw_orgao['poder'].isnull()].nometipoadministracao.value_counts(dropna=False)

nometipoadministracao
ADMINISTRACAO DIRETA MUNICIPAL    474
FUNDOS                              5
ADMINISTRACAO DIRETA                3
FUNDACAO                            1
ADMINISTRACAO DIRETA ESTADUAL       1
Name: count, dtype: int64

484 dos registros sem o valor da coluna `poder`, quase todos se referem à Administração Direta Municipal.
#### Parece ser possível preencher os 484 valores nulos da coluna `poder` a partir da coluna `nometipoadministracao`

### `esfera`
Esfera governamental (F – Federal, E – Estadual, M – Municipal)

In [18]:
raw_orgao.esfera.value_counts(False, dropna=False)

esfera
M      8021
E      2629
F      1138
NaN      32
Name: count, dtype: int64

#### (TO DO) Analisar os 32 casos em que a coluna `esfera` está vazia.

In [19]:
raw_orgao[raw_orgao['esfera'].isnull()].head(3)

,codigoorgao,nomeorgao,nomemnemonicoorgao,cnpjcpforgao,codigoorgaovinculado,cnpjcpforgaovinculado,nomeorgaovinculado,codigoorgaosuperior,cnpjcpforgaosuperior,nomeorgaosuperior,codigotipoadministracao,nometipoadministracao,poder,esfera,usosisg,statusorgao,datahoramovimento,dt_ingest
44,91800,ORGANIZACOES SOCIAIS,ORGANIZ. SOCIAIS,0,NaN,NaN,NaN,NaN,NaN,NaN,15,EMPRESA PRIVADA,E,NaN,True,True,2007-11-30T23:00:00,2026-06-27T04:01:16.491123
71,93000,REGIAO NORTE,REGIAO NORTE,0,99900.0,0,REPUBLICA FEDERATIVA DO BRASIL,NaN,NaN,NaN,11,ADMINISTRACAO DIRETA ESTADUAL,E,NaN,True,True,2007-11-30T23:00:00,2026-06-27T04:01:16.491123
73,20925,CALAMIDADES PUBLICAS - FUNCAP,FUNCAP,0,20101.0,00394411000109,PRESIDENCIA DA REPUBLICA,20000.0,00394411000109,PRESIDENCIA DA REPUBLICA - PRES,7,FUNDOS,E,NaN,True,True,2004-12-29T11:58:00,2026-06-27T04:01:16.491123


### `usosisg`
Indica se o órgão utiliza o SISG (0 – False/Não, 1 – True/Sim)

In [20]:
raw_orgao.usosisg.value_counts(dropna=False)

usosisg
True     11741
False       79
Name: count, dtype: int64

#### (TO DO) Analisar 79 casos de órgãos que não usam o SISG
(Sistema de Serviços Gerais é o conjunto de regras e diretrizes que organiza a logística pública federal)

In [21]:
raw_orgao[raw_orgao['usosisg'] == False].head()

,codigoorgao,nomeorgao,nomemnemonicoorgao,cnpjcpforgao,codigoorgaovinculado,cnpjcpforgaovinculado,nomeorgaovinculado,codigoorgaosuperior,cnpjcpforgaosuperior,nomeorgaosuperior,codigotipoadministracao,nometipoadministracao,poder,esfera,usosisg,statusorgao,datahoramovimento,dt_ingest
3,15000,JUSTICA DO TRABALHO,TST,00509968000148,NaN,NaN,NaN,NaN,NaN,NaN,1,ADMINISTRACAO DIRETA,L,F,False,True,2026-05-26T11:49:00,2026-06-27T04:01:16.491123
68,10000,SUPREMO TRIBUNAL FEDERAL,STF,531640000128,NaN,NaN,NaN,NaN,NaN,NaN,1,ADMINISTRACAO DIRETA,L,F,False,True,2007-11-30T23:00:00,2026-06-27T04:01:43.018081
70,97000,REGIAO CENTRO-OESTE,REGIAO CENTRO-OESTE,0,99900.0,0,REPUBLICA FEDERATIVA DO BRASIL,NaN,NaN,NaN,11,ADMINISTRACAO DIRETA ESTADUAL,E,E,False,True,2007-11-30T23:00:00,2026-06-27T04:01:16.491123
72,95000,REGIAO SUDESTE,REGIAO SUDESTE,0,99900.0,0,REPUBLICA FEDERATIVA DO BRASIL,NaN,NaN,NaN,11,ADMINISTRACAO DIRETA ESTADUAL,E,M,False,True,2007-11-30T23:00:00,2026-06-27T04:01:16.491123
78,45283,INSTITUTO DE RESSEGUROS DO BRASIL,IRB,0,25000.0,00394460000141,MINISTERIO DA FAZENDA,20101.0,00394411000109,PRESIDENCIA DA REPUBLICA,6,ECONOMIA MISTA,E,F,False,True,2007-11-30T23:00:00,2026-06-27T04:01:16.491123


### `statusorgao`
Status do órgão (0 – False/Inativo, 1 – True/Ativo)

In [22]:
raw_orgao.statusorgao.value_counts(dropna=False)

statusorgao
True    11820
Name: count, dtype: int64

#### Todos os órgãos estão ativos

## `raw_uasg`
Unidades Administrativas de Serviços Gerais — unidades compradoras dentro dos órgãos.

| Coluna | Descrição |
|---|---|
| `codigouasg` **PK** | Código da UASG (SIASG) |
| `codigoorgao` **FK** → `raw_orgao` | Órgão ao qual pertence |
| `nomeuasg` | Nome da unidade |
| `cnpjcpfuasg` | CNPJ da UASG |
| `siglauf` | Estado (UF) |
| `codigomunicipioibge` | Código IBGE do município |
| `nomemunicipioibge` | Nome do município |
| `statusuasg` | Ativo/inativo |

In [23]:
raw_uasg.shape

(21926, 23)

In [24]:
raw_uasg.duplicated().sum()

0

### `codigouasg`
Código da UASG

In [25]:
raw_uasg.codigouasg.duplicated().sum()

0

#### Quase 22k unidades compradoras registradas

In [26]:
raw_uasg.head()

,codigouasg,nomeuasg,usosisg,adesaosiasg,siglauf,codigomunicipio,codigomunicipioibge,nomemunicipioibge,codigounidadepolo,nomeunidadepolo,codigounidadeespelho,nomeunidadeespelho,uasgcadastradora,cnpjcpfuasg,codigoorgao,cnpjcpforgao,cnpjcpforgaovinculado,cnpjcpforgaosuperior,codigosiorg,statusuasg,dataimplantacaosidec,datahoramovimento,dt_ingest
0,030100,TRIBUNAL DE JUSTICA DO ESTADO DO RJ,False,True,RJ,60011,3304557.0,RIO DE JANEIRO,0,NaN,0,NaN,False,NaN,95325,28538734000148,42498600000171,0,NaN,True,2002-10-01T03:00:00.000+00:00,2022-12-17T17:09:00,2026-06-27T04:00:08.622297
1,514425,FRGPS - GERÊNCIA EXECUTIVA JUNDIAÍ,False,False,SP,66192,3525904.0,JUNDIAÍ,0,NaN,0,NaN,False,NaN,37904,16727230000197,NaN,NaN,NaN,True,2017-06-27T03:00:00.000+00:00,2017-12-16T16:53:00,2026-06-27T04:00:08.622297
2,514836,FRGPS - APS SÃO JOÃO DEL REI,False,False,MG,52493,3162500.0,SÃO JOÃO DEL REI,0,NaN,0,NaN,False,NaN,37904,16727230000197,NaN,NaN,NaN,True,2017-06-23T03:00:00.000+00:00,2017-12-16T16:15:00,2026-06-27T04:00:08.622297
3,513918,FRGPS - GERENCIA EXECUTIVA PASSO FUNDO,False,False,RS,87858,4314100.0,PASSO FUNDO,0,NaN,0,NaN,False,NaN,37904,16727230000197,NaN,NaN,NaN,True,2017-06-21T03:00:00.000+00:00,2017-12-16T15:14:00,2026-06-27T04:00:08.622297
4,080104,ESP-CONSELHO ESTADUAL DE EDUCACAO-CEE,False,True,SP,71072,3550308.0,SÃO PAULO,990000,ESP-SECRETARIA DE GESTAO E GOVERNO DIGITAL,0,NaN,False,NaN,95561,46384111000140,46379400000150,0,NaN,True,NaN,2024-03-20T11:46:00,2026-06-27T04:00:08.622297


#### (TO DO) Analisar as uasg com nomes duplicados. Baixa prioridade, parece ok

### `nomeuasg`
Nome da UASG

In [27]:
raw_uasg.nomeuasg.duplicated().sum()

792

In [28]:
raw_uasg[raw_uasg.nomeuasg.duplicated(keep=False)].sort_values('nomeuasg')

,codigouasg,nomeuasg,usosisg,adesaosiasg,siglauf,codigomunicipio,codigomunicipioibge,nomemunicipioibge,codigounidadepolo,nomeunidadepolo,codigounidadeespelho,nomeunidadeespelho,uasgcadastradora,cnpjcpfuasg,codigoorgao,cnpjcpforgao,cnpjcpforgaovinculado,cnpjcpforgaosuperior,codigosiorg,statusuasg,dataimplantacaosidec,datahoramovimento,dt_ingest
6477,160339,1 BATALHAO DE ENGENHARIA DE CONSTRUCAO,False,True,RN,16390,2402006.0,CAICÓ,160549,10º CENTRO DE GESTÃO CONT E FIN DO EXERCITO,0,NaN,False,394452003110,52121,00394452000103,03277610000125,00394411000109,80652,True,2002-04-21T03:00:00.000+00:00,2026-06-09T15:02:00,2026-06-27T04:01:12.188883
21553,167339,1 BATALHAO DE ENGENHARIA DE CONSTRUCAO,False,True,RN,16390,2402006.0,CAICÓ,160339,1 BATALHAO DE ENGENHARIA DE CONSTRUCAO,160339,1 BATALHAO DE ENGENHARIA DE CONSTRUCAO,True,0,52904,00394452054700,00394452000103,03277610000125,44392,True,NaN,2025-08-22T14:07:00,2026-06-27T04:00:57.208317
5576,160030,1 COMPANHIA DE INFANTARIA,False,True,BA,37818,2924009.0,PAULO AFONSO,160197,6º CENTRO DE GESTAO CONT E FIN DO EXERCITO,0,NaN,True,394452025947,52121,00394452000103,03277610000125,00394411000109,80636,True,2000-04-15T03:00:00.000+00:00,2026-06-01T09:43:00,2026-06-27T04:01:10.714182
9073,167030,1 COMPANHIA DE INFANTARIA,False,True,BA,38490,2927408.0,SALVADOR,160030,1 COMPANHIA DE INFANTARIA,160030,1 COMPANHIA DE INFANTARIA,False,0,52904,00394452054700,00394452000103,03277610000125,44392,True,NaN,2025-12-05T11:13:00,2026-06-27T04:00:58.695717
21236,167114,10 BATALHAO DE INFANTARIA,False,True,MG,41238.0,3106200.0,BELO HORIZONTE,160114,10 BATALHAO DE INFANTARIA,160114,10 BATALHAO DE INFANTARIA,False,0,52904,00394452054700,00394452000103,03277610000125,44345,True,NaN,2025-08-22T10:49:00,2026-06-27T04:00:55.791167
21129,160114,10 BATALHAO DE INFANTARIA,False,True,MG,47333.0,3136702.0,JUIZ DE FORA,160533,4º CENTRO DE GESTÃO CONT E FIN DO EXERCITO,0,NaN,True,394452005083,52121,00394452000103,03277610000125,00394411000109,80750,True,2000-04-15T03:00:00.000+00:00,2025-08-22T14:42:00,2026-06-27T04:00:55.791167
1239,160184,10 ESQUADRAO DE CAVALARIA MECANIZADO,False,True,PE,25313,2611606.0,RECIFE,160543,7º CENTRO DE GESTÃO CONT E FIN DO EXÉRCITO,0,NaN,False,394452030940,52121,00394452000103,03277610000125,00394411000109,80629,True,2000-04-15T03:00:00.000+00:00,2026-01-30T14:57:00,2026-06-27T04:01:00.064947
21360,167184,10 ESQUADRAO DE CAVALARIA MECANIZADO,False,True,PE,25313.0,2611606.0,RECIFE,160184,10 ESQUADRAO DE CAVALARIA MECANIZADO,160184,10 ESQUADRAO DE CAVALARIA MECANIZADO,False,0,52904,00394452054700,00394452000103,03277610000125,44392,True,NaN,2025-08-22T14:07:00,2026-06-27T04:00:55.791167
21117,167107,11 CIRCUNSCRICAO DE SERVICO MILITAR,False,True,MG,41238.0,3106200.0,BELO HORIZONTE,160107,11 CIRCUNSCRICAO DE SERVICO MILITAR,160107,11 CIRCUNSCRICAO DE SERVICO MILITAR,False,0,52904,00394452054700,00394452000103,03277610000125,44345,True,NaN,2025-08-22T10:49:00,2026-06-27T04:00:55.791167
21328,160107,11 CIRCUNSCRICAO DE SERVICO MILITAR,False,True,MG,41238.0,3106200.0,BELO HORIZONTE,160533,4º CENTRO DE GESTÃO CONT E FIN DO EXERCITO,0,NaN,False,394452015208,52121,00394452000103,03277610000125,00394411000109,80737,True,2000-04-15T03:00:00.000+00:00,2025-08-22T13:46:00,2026-06-27T04:00:55.791167


### `usosisg`
Indica se a UASG utiliza o SISG (0 – False/Não, 1 – True/Sim)

In [29]:
raw_uasg.usosisg.value_counts(1, dropna=False)

usosisg
False    0.875582
True     0.124418
Name: proportion, dtype: float64

#### A diferença entre as colunas `usosisg` e `adesaosiasg`
O SISG (Sistema de Serviços Gerais) é o conjunto de regras e diretrizes que organiza a logística pública federal, enquanto o SIASG (Sistema Integrado de Administração de Serviços Gerais) é a plataforma de computador usada para colocar essas regras em prática no dia a dia

In [30]:
raw_uasg.adesaosiasg.value_counts(1, dropna=False)

adesaosiasg
True     0.947004
False    0.052996
Name: proportion, dtype: float64

#### Apenas 12% no `usosisg` e 94% no `adesaosiasg`

### `siglauf`
Sigla da Unidade Federativa (UF)

In [31]:
raw_uasg.siglauf.value_counts(dropna=False).tail()

siglauf
SE    277
AC    185
RR    174
AP    172
EX     23
Name: count, dtype: int64

In [32]:
raw_uasg[raw_uasg['siglauf'] == 'EX']

,codigouasg,nomeuasg,usosisg,adesaosiasg,siglauf,codigomunicipio,codigomunicipioibge,nomemunicipioibge,codigounidadepolo,nomeunidadepolo,codigounidadeespelho,nomeunidadeespelho,uasgcadastradora,cnpjcpfuasg,codigoorgao,cnpjcpforgao,cnpjcpforgaovinculado,cnpjcpforgaosuperior,codigosiorg,statusuasg,dataimplantacaosidec,datahoramovimento,dt_ingest
5139,120090,COMISSÃO AERONÁUTICA BRASILEIRA EM WASHINGTON,False,True,EX,97071,NaN,NaN,120002,DIRETORIA DE ECON. E FINANçAS DA AERONáUTICA,0,NaN,False,394429004106,52111,00394429000100,03277610000125,00394411000109,10399,True,1999-07-15T03:00:00.000+00:00,2026-05-07T12:23:00,2026-06-27T04:01:08.991964
8403,670201,FUNDO NAVAL/CNBW,False,True,EX,97071,NaN,NaN,770201,FUNDO NAVAL/CNBW,770201,FUNDO NAVAL/CNBW,False,0,52132,00394502047370,00394502002864,03277610000125,NaN,True,NaN,2025-05-23T14:26:00,2026-06-27T04:00:34.444904
13696,120092,SECRET.DE ECON.E FINANCAS DA AERON.- EXTERIOR,False,True,EX,97071.0,NaN,NaN,0,NaN,0,NaN,False,0,52111,00394429000100,03277610000125,00394411000109,NaN,True,1999-07-15T03:00:00.000+00:00,2025-05-06T18:30:00,2026-06-27T04:00:31.425511
14565,870200,COMISSAO NAVAL BRASILEIRA EM WASHINGTON,False,True,EX,97071.0,NaN,NaN,770200,COMISSAO NAVAL BRASILEIRA EM WASHINGTON,770200,COMISSAO NAVAL BRASILEIRA EM WASHINGTON,False,0,52133,00394502051644,00394502000144,03277610000125,NaN,True,NaN,2025-05-23T14:26:00,2026-06-27T04:00:35.901748
14642,670200,COMISSAO NAVAL BRASILEIRA EM WASHINGTON,False,True,EX,97071.0,NaN,NaN,770200,COMISSAO NAVAL BRASILEIRA EM WASHINGTON,770200,COMISSAO NAVAL BRASILEIRA EM WASHINGTON,False,0,52132,00394502047370,00394502002864,03277610000125,NaN,True,NaN,2025-05-23T14:26:00,2026-06-27T04:00:35.901748
15235,910962,PETROBRAS INTERNACIONAL BRASPETRO B. V.,False,False,EX,97071,NaN,NaN,910816,PETROLEO BRASILEIRO S/A,0,NaN,False,0,91084,02709449000159,37115383000153,00394411000109,NaN,True,NaN,2010-07-07T18:30:00,2026-06-27T04:00:37.578958
16810,670101,FUNDO NAVAL/CNBE - SISTEMA - EXTERIOR,False,True,EX,97071,NaN,NaN,770101,FUNDO NAVAL/CNBE,770101,FUNDO NAVAL/CNBE,False,0,52132,00394502047370,00394502002864,03277610000125,NaN,True,NaN,2025-05-23T14:26:00,2026-06-27T04:00:42.440478
17956,120093,SUBDIRETORIA DE PAGAMENTO DE PESSOAL/EXTERIOR,False,True,EX,97071,NaN,NaN,0,NaN,0,NaN,False,394429015566,52111,00394429000100,03277610000125,00394411000109,NaN,True,1999-07-15T03:00:00.000+00:00,2025-05-06T18:30:00,2026-06-27T04:00:45.635427
18708,120091,COMISSÃO AERONÁUTICA BRASILEIRA NA EUROPA,False,True,EX,97071.0,NaN,NaN,120002,DIRETORIA DE ECON. E FINANçAS DA AERONáUTICA,0,NaN,False,394429004289,52111,00394429000100,03277610000125,00394411000109,69134,True,1999-07-15T03:00:00.000+00:00,2025-05-06T18:30:00,2026-06-27T04:00:48.468768
18975,110406,REPRESENT.DO BRASIL NA JUNTA INTERAM.DEFESA,False,True,EX,97071.0,NaN,NaN,0,NaN,0,NaN,False,55230000000099,52000,03277610000125,00394411000109,00394411000109,41930,True,2008-01-01T02:00:00.000+00:00,2025-05-23T14:24:00,2026-06-27T04:00:48.468768


In [33]:
raw_uasg[raw_uasg['siglauf'] == 'EX'].codigomunicipio.value_counts(dropna=False)

codigomunicipio
97071.0    10
97071       9
60011       3
60011.0     1
Name: count, dtype: int64

In [34]:
raw_uasg[raw_uasg['siglauf'] == 'EX'].codigomunicipioibge.value_counts(dropna=False)

codigomunicipioibge
NaN    23
Name: count, dtype: int64

### `codigomunicipio`
Código do município no SIASG

In [35]:
raw_uasg.codigomunicipio.value_counts(dropna=False).head()

codigomunicipio
97012      1010
71072       765
60011       751
25313       559
97012.0     464
Name: count, dtype: int64

In [36]:
raw_uasg.codigomunicipioibge.value_counts(dropna=False).head(10)

codigomunicipioibge
5300108.0    1426
3304557.0    1114
3550308.0     977
2611606.0     748
1501402.0     312
1302603.0     270
NaN           255
3106200.0     253
4314902.0     252
2927408.0     247
Name: count, dtype: int64

In [37]:
raw_uasg[raw_uasg.codigomunicipioibge.isnull()]

,codigouasg,nomeuasg,usosisg,adesaosiasg,siglauf,codigomunicipio,codigomunicipioibge,nomemunicipioibge,codigounidadepolo,nomeunidadepolo,codigounidadeespelho,nomeunidadeespelho,uasgcadastradora,cnpjcpfuasg,codigoorgao,cnpjcpforgao,cnpjcpforgaovinculado,cnpjcpforgaosuperior,codigosiorg,statusuasg,dataimplantacaosidec,datahoramovimento,dt_ingest
34,514640,FRGPS - GERÊNCIA EXECUTIVA SALVADOR,False,False,SP,38490,NaN,NaN,0,NaN,0,NaN,False,NaN,37904,16727230000197,NaN,NaN,NaN,True,2017-06-28T03:00:00.000+00:00,2017-12-16T10:24:00,2026-06-27T04:00:08.622297
130,975007,FUNDO MUNICIPAL DE SAUDE MARCAÇÃO,False,True,PB,4847,NaN,NaN,0,NaN,0,NaN,False,NaN,87706,12370254000180,NaN,NaN,NaN,True,NaN,2024-08-11T17:47:00,2026-06-27T04:00:08.622297
142,975529,FUNDO M. S. SÃO LUIZ DO PARAITINGA,False,True,SP,71013,NaN,NaN,0,NaN,0,NaN,False,NaN,88228,13011161000122,NaN,NaN,NaN,True,NaN,2024-08-24T17:47:00,2026-06-27T04:00:08.622297
154,974907,FUNDO M. S. SANTO ANTÔNIO DO RETIRO,False,True,MG,7080,NaN,NaN,0,NaN,0,NaN,False,NaN,87606,13975130000191,NaN,NaN,NaN,True,NaN,2024-08-11T17:47:00,2026-06-27T04:00:08.622297
232,975596,FUNDO MUNICIPAL DE SAUDE COUTO MAGALHÃES,False,True,TO,93211,NaN,NaN,0,NaN,0,NaN,False,NaN,88295,11252797000130,NaN,NaN,NaN,True,NaN,2024-08-24T17:47:00,2026-06-27T04:00:08.622297
792,931207,MSC-CÂMARA MUNICIPAL DE SÃO MIGUEL DO OESTE,False,True,SC,83399,NaN,NaN,0,NaN,0,NaN,False,NaN,85060,78484573000125,82951229000176,0,NaN,True,2026-01-08T03:00:00.000+00:00,2026-01-08T09:16:00,2026-06-27T04:00:58.695717
834,987843,PREF. MUN. DE SANTA CRUZ DE M. CASTELO,False,True,PR,78433,NaN,NaN,0,NaN,0,NaN,False,0,91373,75462820000102,76416940000128,0,NaN,True,2024-02-07T03:00:00.000+00:00,2026-01-12T18:50:00,2026-06-27T04:00:58.695717
840,985819,MRJ-PREFEITURA MUNICIPAL CAMPOS DE GOYTACAZES,False,True,RJ,58190,NaN,NaN,0,NaN,0,NaN,False,0,91368,29116894000161,42498600000171,0,NaN,True,2026-01-12T03:00:00.000+00:00,2026-01-12T11:04:00,2026-06-27T04:00:58.695717
841,463070,MRJ-CONSÓRCIO P.I.D.NORTE NOROESTE FLUMINENSE,False,True,RJ,58190,NaN,NaN,0,NaN,0,NaN,False,00000000000000,85117,32233059000116,29116894000161,42498600000171,NaN,True,2026-01-12T03:00:00.000+00:00,2026-01-12T11:27:00,2026-06-27T04:00:58.695717
979,125397,EPTA GOIÂNIA - TAGO,False,True,TO,53791,NaN,NaN,125001,INFRAERO CENTRO CORPORATIVO/SEDE,0,NaN,False,NaN,20213,00352294000110,49582441000138,00394411000109,NaN,True,2014-05-19T03:00:00.000+00:00,2025-01-21T15:56:00,2026-06-27T04:00:10.449320


#### 1,1% de valores nulos em `codigomunicipioibge`

#### (TO DO) Investigar as linhas com valores nulos de `codigomunicipioibge`

### `nomemunicipioibge`
Nome do município conforme o IBGE

In [38]:
raw_uasg.nomemunicipioibge.value_counts(1, dropna=False).head(10)

nomemunicipioibge
BRASÍLIA          0.066998
RIO DE JANEIRO    0.051628
SÃO PAULO         0.046475
RECIFE            0.034571
BELÉM             0.016464
MANAUS            0.012770
PORTO ALEGRE      0.011995
BELO HORIZONTE    0.011812
NaN               0.011630
SALVADOR          0.011584
Name: proportion, dtype: float64

In [39]:
raw_uasg[raw_uasg.nomemunicipioibge.isna()].head()

,codigouasg,nomeuasg,usosisg,adesaosiasg,siglauf,codigomunicipio,codigomunicipioibge,nomemunicipioibge,codigounidadepolo,nomeunidadepolo,codigounidadeespelho,nomeunidadeespelho,uasgcadastradora,cnpjcpfuasg,codigoorgao,cnpjcpforgao,cnpjcpforgaovinculado,cnpjcpforgaosuperior,codigosiorg,statusuasg,dataimplantacaosidec,datahoramovimento,dt_ingest
34,514640,FRGPS - GERÊNCIA EXECUTIVA SALVADOR,False,False,SP,38490,NaN,NaN,0,NaN,0,NaN,False,NaN,37904,16727230000197,NaN,NaN,NaN,True,2017-06-28T03:00:00.000+00:00,2017-12-16T10:24:00,2026-06-27T04:00:08.622297
130,975007,FUNDO MUNICIPAL DE SAUDE MARCAÇÃO,False,True,PB,4847,NaN,NaN,0,NaN,0,NaN,False,NaN,87706,12370254000180,NaN,NaN,NaN,True,NaN,2024-08-11T17:47:00,2026-06-27T04:00:08.622297
142,975529,FUNDO M. S. SÃO LUIZ DO PARAITINGA,False,True,SP,71013,NaN,NaN,0,NaN,0,NaN,False,NaN,88228,13011161000122,NaN,NaN,NaN,True,NaN,2024-08-24T17:47:00,2026-06-27T04:00:08.622297
154,974907,FUNDO M. S. SANTO ANTÔNIO DO RETIRO,False,True,MG,7080,NaN,NaN,0,NaN,0,NaN,False,NaN,87606,13975130000191,NaN,NaN,NaN,True,NaN,2024-08-11T17:47:00,2026-06-27T04:00:08.622297
232,975596,FUNDO MUNICIPAL DE SAUDE COUTO MAGALHÃES,False,True,TO,93211,NaN,NaN,0,NaN,0,NaN,False,NaN,88295,11252797000130,NaN,NaN,NaN,True,NaN,2024-08-24T17:47:00,2026-06-27T04:00:08.622297


#### (PERGUNTA) o que é unidade polo da coluna `codigounidadepolo`?

### `codigounidadepolo`
Código da unidade polo

In [40]:
raw_uasg.codigounidadepolo.value_counts(1, dropna=False).head()

codigounidadepolo
0         0.740719
990000    0.057603
772000    0.009532
125001    0.005747
120002    0.005108
Name: proportion, dtype: float64

#### 74% dos `codigounidadepolo` igual a 0 em vez de NaN

### `nomeunidadepolo`
Nome da unidade polo

In [41]:
raw_uasg.nomeunidadepolo.value_counts(1, dropna=False).head()

nomeunidadepolo
NaN                                             0.741312
ESP-SECRETARIA DE GESTAO E GOVERNO DIGITAL      0.057603
DIRETORIA DE GESTÃO ORÇAMENTÁRIA DA MARINHA     0.009532
INFRAERO CENTRO CORPORATIVO/SEDE                0.005747
DIRETORIA DE ECON. E FINANçAS DA AERONáUTICA    0.005108
Name: proportion, dtype: float64

### `codigounidadeespelho`
Código da unidade espelho

In [42]:
raw_uasg.codigounidadeespelho.value_counts(1, dropna=False).head()

codigounidadeespelho
0         0.953845
110005    0.000137
110407    0.000137
772003    0.000091
200081    0.000091
Name: proportion, dtype: float64

#### 95% dos `codigounidadeespelho` igual a 0 em vez de NaN

### `nomeunidadeespelho`
Nome da unidade espelho

In [43]:
raw_uasg.nomeunidadeespelho.value_counts(1, dropna=False).head()

nomeunidadeespelho
NaN                                              0.953845
COORDENACAO DE PLANEJAMENTO E ORCAMENTO - PR     0.000137
ESTADO-MAIOR DAS FORCAS ARMADAS - UNID.ORC.      0.000137
RESERVA TECNICA DADM                             0.000091
SUPERINTENDENCIA REG.DEP.POLICIA FEDERAL - PI    0.000091
Name: proportion, dtype: float64

In [44]:
raw_uasg.nomeunidadeespelho.value_counts(0, dropna=False).head()

nomeunidadeespelho
NaN                                              20914
COORDENACAO DE PLANEJAMENTO E ORCAMENTO - PR         3
ESTADO-MAIOR DAS FORCAS ARMADAS - UNID.ORC.          3
RESERVA TECNICA DADM                                 2
SUPERINTENDENCIA REG.DEP.POLICIA FEDERAL - PI        2
Name: count, dtype: int64

In [45]:
raw_uasg[raw_uasg['codigounidadeespelho'] != '0'].head()

,codigouasg,nomeuasg,usosisg,adesaosiasg,siglauf,codigomunicipio,codigomunicipioibge,nomemunicipioibge,codigounidadepolo,nomeunidadepolo,codigounidadeespelho,nomeunidadeespelho,uasgcadastradora,cnpjcpfuasg,codigoorgao,cnpjcpforgao,cnpjcpforgaovinculado,cnpjcpforgaosuperior,codigosiorg,statusuasg,dataimplantacaosidec,datahoramovimento,dt_ingest
493,672003,RESERVA TECNICA DADM,False,True,RJ,60011,3304557.0,RIO DE JANEIRO,772003,RESERVA TECNICA DADM,772003,RESERVA TECNICA DADM,False,0,52132,00394502047370,00394502002864,03277610000125,NaN,True,NaN,2024-11-14T14:08:00,2026-06-27T04:00:34.444904
502,200390,SUPERINTENDENCIA REG.DEP.POLICIA FEDERAL - PI,True,True,PI,12190,2211001.0,TERESINA,0,NaN,200081,SUPERINTENDENCIA REG.DEP.POLICIA FEDERAL - PI,True,0,30108,00394494000136,00394494000136,00394411000109,23014,True,NaN,2025-11-06T11:05:00,2026-06-27T04:00:58.695717
505,167027,4 BATALHAO DE ENGENHARIA DE CONSTRUCAO,False,True,BA,33634,2903201.0,BARREIRAS,160054,11º CENTRO DE GESTÃO CONT E FIN DO EXERCITO,160027,4 BATALHAO DE ENGENHARIA DE CONSTRUCAO - MEX,False,0,52904,00394452054700,00394452000103,03277610000125,44391,True,NaN,2025-11-06T10:10:00,2026-06-27T04:00:58.695717
632,167005,54 BATALHAO DE INFANTARIA DE SELVA,False,True,AM,2356,1301704.0,HUMAITÁ,160005,54 BATALHAO DE INFANTARIA DE SELVA/AM,160005,54 BATALHAO DE INFANTARIA DE SELVA/AM,False,0,52904,00394452054700,00394452000103,03277610000125,7806,True,NaN,2025-12-08T14:51:00,2026-06-27T04:00:58.695717
663,167487,CENTRO PREP OFICIAIS DA RESERVA DE SÃO PAULO,False,True,SP,71072,3550308.0,SÃO PAULO,160487,CENTRO PREP OFICIAIS DA RESERVA DE SÃO PAULO,160487,CENTRO PREP OFICIAIS DA RESERVA DE SÃO PAULO,False,0,52904,00394452054700,00394452000103,03277610000125,44343,True,NaN,2025-12-12T08:06:00,2026-06-27T04:00:58.695717


In [46]:
raw_uasg[raw_uasg['codigounidadeespelho'] != '0'].shape

(1012, 23)

In [47]:
raw_uasg[raw_uasg['nomeunidadepolo'] == raw_uasg['nomeunidadeespelho']].shape

(932, 23)

In [48]:
raw_uasg[(raw_uasg['codigounidadeespelho'] != '0') & (raw_uasg['nomeunidadepolo'] != raw_uasg['nomeunidadeespelho'])].shape

(80, 23)

#### 1k uags tem unidade espelho, dessas apenas 80 são diferentes da unidade de polo.

### `uasgcadastradora`
Indica se a UASG é cadastradora (0 – False/Não, 1 – True/Sim)

In [49]:
raw_uasg.uasgcadastradora.value_counts(1, dropna=False)

uasgcadastradora
False    0.89159
True     0.10841
Name: proportion, dtype: float64

#### 89% das uasgs não são cadastradoras

### `cnpjcpfuasg`
CNPJ da UASG

In [50]:
raw_uasg.cnpjcpfuasg.value_counts(1, dropna=False).head()

cnpjcpfuasg
NaN               0.608319
0                 0.274241
00000000000000    0.003101
24134488000108    0.000228
15180714000104    0.000137
Name: proportion, dtype: float64

#### Apenas 12% das uasgs tem cnpj

### `codigoorgao`
Código do órgão

In [51]:
raw_uasg.codigoorgao.value_counts(1, dropna=False).head()

codigoorgao
52131    0.023762
95120    0.023579
52121    0.023306
52904    0.020478
85622    0.019247
Name: proportion, dtype: float64

In [52]:
raw_uasg.cnpjcpforgao.value_counts(1, dropna=False).head()

cnpjcpforgao
00394502000144    0.023762
18715615000160    0.023579
00394452000103    0.023306
00394452054700    0.020478
10565000000192    0.019247
Name: proportion, dtype: float64

In [53]:
raw_uasg.cnpjcpforgaovinculado.value_counts(1, dropna=False).head()

cnpjcpforgaovinculado
0                 0.109596
46379400000150    0.091444
NaN               0.077716
03277610000125    0.057648
00394411000109    0.054502
Name: proportion, dtype: float64

In [54]:
raw_uasg.cnpjcpforgaosuperior.value_counts(1, dropna=False).head()

cnpjcpforgaosuperior
0                 0.523306
00394411000109    0.225531
NaN               0.088707
03277610000125    0.040089
46379400000150    0.019520
Name: proportion, dtype: float64

#### `cnpjcpforgao` 100% preenchida, `cnpjcpforgaovinculado`80% preenchida e `cnpjcpforgaosuperior` com menos de 50% de preenchimento
Valores `0` e `NaN` considerados como vazios.

### `codigosiorg`
Código do SIORG

In [55]:
raw_uasg.codigosiorg.value_counts(1, dropna=False).head()

codigosiorg
NaN      0.819256
6659     0.002736
44344    0.001961
44392    0.001733
7806     0.001459
Name: proportion, dtype: float64

#### Menos de 18% de preenchimento para `codigosiorg`

### `statusuasg`
Status da UASG (0 – False/Inativo, 1 – True/Ativo)

In [56]:
raw_uasg.statusuasg.value_counts(1, dropna=False).head()

statusuasg
True    1.0
Name: proportion, dtype: float64

#### 100% das uasgs ativas

### `dataimplantacaosidec`
Data de implantação no SIDEC

In [57]:
raw_uasg.dataimplantacaosidec.value_counts(1, dropna=False).head()

dataimplantacaosidec
NaN                              0.169206
1999-07-15T03:00:00.000+00:00    0.107270
2000-04-15T03:00:00.000+00:00    0.019019
2001-12-31T02:00:00.000+00:00    0.006796
2026-03-31T03:00:00.000+00:00    0.006568
Name: proportion, dtype: float64

#### 17% de nulos em `dataimplantacaosidec`
#### (TO DO) Investigar se existe um padrão

In [58]:
orgaos = pd.merge(raw_orgao, raw_uasg, on='codigoorgao', how='outer', indicator='_uasg', suffixes=('_orgao', '_uasg'))

In [59]:
orgaos._uasg.value_counts()

_uasg
both          21926
left_only       211
right_only        0
Name: count, dtype: int64

In [60]:
orgaos.shape

(22137, 41)

In [61]:
orgaos_sem_uasg = list(orgaos[orgaos['_uasg'] == 'left_only'].nomeorgao.values)

In [62]:
orgaos_sem_uasg

['MINISTERIO ADM.FED.REFORMA ESTADO-EM EXTINCAO', 'SECRETARIA DA CULTURA', 'SECRETARIA DA CIENCIA E TECNOLOGIA', 'SEC.ESPEC.DE AGRIC.FAMIL.E DO DESENV.AGRARIO', 'NUCLEBRAS EQUIPAMENTOS PESADOS S/A', 'INDUSTRIAS NUCLEARES DO BRASIL S/A', 'FUNDACAO DO CINEMA BRASILEIRO', 'FUNDACAO NACIONAL PRO-LEITURA', 'FUNDACAO CENTRO TECNOLOGICO PARA INFORMATICA', 'SUPERINTENDENCIA DO DESENVOLV. DA AMAZONIA', 'SECRETARIA DE PATRIMONIO DA UNIAO/MP', 'CALAMIDADES PUBLICAS - FUNCAP', 'MINISTERIO DO BEM-ESTAR SOCIAL-EM EXTINCAO', 'FUND.CENTRO BRAS.INF.ADOLESCENCIA-EM EXTINCAO', 'FUNDACAO LEGIAO BRAS.ASSISTENCIA-EM EXTINCAO', 'FUNDO DE PREVIDENCIA E ASSISTENCIA SOCIAL', 'TELECOMUNICAÇÕES BRASILEIRAS S/A', 'FUNDO ESP. DE TREINAMENTO E DESENVOLVIMENTO', 'SUPERINTENDENCIA NAC.ABASTECIMENTO-EM EXTINCA', 'BANCO CENTRAL DO BRASIL', 'RECEITA FEDERAL DO BRASIL', 'ESCOLA DE ADMINISTRACAO FAZENDARIA/MF', 'PROCURADORIA-GERAL DA FAZENDA NACIONAL', 'SUBSECRET.DE PLANEJ.,ORCAMENTO E ADM. \xad SPOA', 'SECRETARIA DO TESOU

#### (TO DO) verificar se é normal orgao não ter uasg, verificar se esses orgão aparecem com compras, pode estar relacionado ao corte temporal